# Mapa de abstenção — Eleição 2026, 1.º turno, Presidente

Fonte: Portal de Dados Abertos do TSE (`eleitorado_local_votacao_2026` e `votacao_secao_2026_BR`).

**Definições adotadas**

| Grandeza | Cálculo |
|---|---|
| Aptos | `QT_ELEITOR_ELEICAO_FEDERAL` — uma linha por seção, **apenas do 1.º turno** |
| Comparecimento | soma de `QT_VOTOS` para Presidente (nominais + brancos + nulos) |
| Abstenção | Aptos − Comparecimento |
| % Abstenção | 100 × Abstenção ÷ Aptos |

**Chaves**

- Seção: `SG_UF, CD_MUNICIPIO, NR_ZONA, NR_SECAO`
- Local de votação: `SG_UF, CD_MUNICIPIO, NR_ZONA, NR_LOCAL_VOTACAO`
  (o número do local **só é único dentro da zona eleitoral**)

Execute as células em ordem. As células de validação interrompem a execução se os totais deixarem de fechar.

## 1. Configuração

In [1]:
import os
import io
import json
import html
import zipfile
from pathlib import Path

import numpy as np
import pandas as pd
import requests

ANO = 2026
TURNO = 1
UF_EXEMPLO = "DF"      # UF usada nas tabelas e no mapa detalhado (folium)

# Pasta principal (no Colab: /content/tse2026)
BASE = Path(os.environ.get("TSE_BASE", "/content/tse2026"))
CSV = BASE / "csv"
MAPAS = BASE / "mapas"
ZIPS = BASE / "zips"
for pasta in [BASE, CSV, MAPAS, ZIPS]:
    pasta.mkdir(parents=True, exist_ok=True)

URL_LOCAIS = ("https://cdn.tse.jus.br/estatistica/sead/odsele/"
              f"eleitorado_locais_votacao/eleitorado_local_votacao_{ANO}.zip")
URL_VOTOS = ("https://cdn.tse.jus.br/estatistica/sead/odsele/"
             f"votacao_secao/votacao_secao_{ANO}_BR.zip")

ARQ_LOCAIS = f"eleitorado_local_votacao_{ANO}_BRASIL.csv"
ARQ_VOTOS = f"votacao_secao_{ANO}_BR.csv"

CHAVE_SECAO = ["SG_UF", "CD_MUNICIPIO", "NR_ZONA", "NR_SECAO"]
CHAVE_LOCAL = ["SG_UF", "CD_MUNICIPIO", "NR_ZONA", "NR_LOCAL_VOTACAO"]
COL_APTOS = "QT_ELEITOR_ELEICAO_FEDERAL"

# Totais oficiais divulgados pelo TSE ao encerrar a apuração do 1.º turno
# (usados apenas para conferência; não entram em nenhum cálculo).
REFERENCIA_TSE = {
    "Aptos": 158_745_502,
    "Comparecimento": 125_275_835,
    "Abstenção": 33_469_244,
    "Taxa (%)": 21.08,
}


def milhar(x):
    # Formata inteiro com separador de milhar brasileiro.
    return f"{int(round(x)):,}".replace(",", ".")


def pct(x, casas=2):
    # Formata percentual com vírgula decimal.
    return f"{x:.{casas}f}".replace(".", ",") + "%"


def formatar_resumo(df):
    # Exibe a tabela de conferência sem notação científica.
    fmt = lambda v, linha: pct(v).rstrip("%") if "Taxa" in linha else milhar(v)
    return df.apply(lambda linha: pd.Series({c: fmt(linha[c], linha.name) for c in df.columns}), axis=1)

## 2. Download dos arquivos do TSE

In [2]:
def baixar(url, destino, tentativas=3):
    # Baixa em blocos para o disco, mostrando o progresso; reaproveita arquivo íntegro já baixado.
    import time
    destino = Path(destino)
    if destino.exists() and zipfile.is_zipfile(destino):
        print(f"Já existe: {destino.name} ({destino.stat().st_size / 1e6:.0f} MB) — download dispensado")
        return destino
    parcial = destino.with_name(destino.name + ".parcial")
    for tentativa in range(1, tentativas + 1):
        try:
            inicio = time.time()
            with requests.get(url, stream=True, timeout=(30, 120)) as r:
                r.raise_for_status()
                total = int(r.headers.get("Content-Length", 0))
                print(f"Baixando {destino.name}" + (f" ({total / 1e6:.0f} MB)" if total else "") + " ...")
                baixado, proximo = 0, 0
                with open(parcial, "wb") as f:
                    for bloco in r.iter_content(chunk_size=4 << 20):
                        f.write(bloco)
                        baixado += len(bloco)
                        if baixado >= proximo:
                            seg = max(time.time() - inicio, 1e-6)
                            print(f"   {baixado / 1e6:7.0f} MB"
                                  + (f" ({100 * baixado / total:3.0f}%)" if total else "")
                                  + f" — {baixado / 1e6 / seg:.1f} MB/s", flush=True)
                            proximo += 25e6
            if not zipfile.is_zipfile(parcial):
                raise IOError("arquivo incompleto ou corrompido")
            parcial.replace(destino)
            print(f"   concluído em {time.time() - inicio:.0f} s")
            return destino
        except (requests.RequestException, IOError) as erro:
            print(f"   tentativa {tentativa}/{tentativas} falhou: {erro}")
    raise IOError(f"Não foi possível baixar {url}")


zf_locais = zipfile.ZipFile(baixar(URL_LOCAIS, ZIPS / f"eleitorado_local_votacao_{ANO}.zip"))
zf_votos = zipfile.ZipFile(baixar(URL_VOTOS, ZIPS / f"votacao_secao_{ANO}_BR.zip"))

print("\nArquivos (locais):", len(zf_locais.namelist()), "| contém BRASIL:", ARQ_LOCAIS in zf_locais.namelist())
print("Arquivos (votação):", zf_votos.namelist())

Baixando eleitorado_local_votacao_2026.zip (176 MB) ...
         4 MB (  2%) — 6.0 MB/s
        25 MB ( 14%) — 14.2 MB/s
        50 MB ( 29%) — 21.2 MB/s
        75 MB ( 43%) — 27.9 MB/s
       101 MB ( 57%) — 28.7 MB/s
       126 MB ( 72%) — 33.0 MB/s
       151 MB ( 86%) — 37.6 MB/s
       176 MB (100%) — 38.1 MB/s
   concluído em 5 s
Baixando votacao_secao_2026_BR.zip (162 MB) ...
         4 MB (  3%) — 7.6 MB/s
        25 MB ( 16%) — 5.6 MB/s
        50 MB ( 31%) — 7.6 MB/s
        75 MB ( 47%) — 9.9 MB/s
       101 MB ( 62%) — 11.3 MB/s
       126 MB ( 78%) — 12.2 MB/s
       151 MB ( 93%) — 12.6 MB/s
   concluído em 13 s

Arquivos (locais): 30 | contém BRASIL: True
Arquivos (votação): ['votacao_secao_2026_BR.csv', 'leiame.pdf']


In [3]:
def ler_csv_tse(zf, nome, desejadas, obrigatorias, texto=()):
    # Lê do ZIP apenas as colunas desejadas que de fato existem no arquivo.
    with zf.open(nome) as f:
        cabecalho = pd.read_csv(f, sep=";", encoding="latin1", nrows=0).columns.tolist()
    faltam = [c for c in obrigatorias if c not in cabecalho]
    if faltam:
        raise KeyError(f"{nome}: colunas obrigatórias ausentes {faltam}. Disponíveis: {cabecalho}")
    usar = [c for c in desejadas if c in cabecalho]
    with zf.open(nome) as f:
        return pd.read_csv(f, sep=";", encoding="latin1", usecols=usar,
                           dtype={c: str for c in texto if c in usar})

## 3. Eleitorado por seção (aptos)

O arquivo `eleitorado_local_votacao` traz **uma linha por seção e por turno**
(`NR_TURNO` = 1 e 2). Sem filtrar o turno, cada seção aparece duas vezes: o eleitorado dobra
(317,5 milhões em vez de 158,7 milhões) e, no `merge`, o comparecimento também é contado duas vezes.

In [4]:
eleitorado_bruto = ler_csv_tse(
    zf_locais, ARQ_LOCAIS,
    desejadas=["NR_TURNO", "DT_ELEICAO", "SG_UF", "CD_MUNICIPIO", "NM_MUNICIPIO",
               "NR_ZONA", "NR_SECAO", "DS_TIPO_SECAO_AGREGADA", "NR_SECAO_PRINCIPAL",
               "NR_LOCAL_VOTACAO", "NM_LOCAL_VOTACAO", "DS_ENDERECO", "NM_BAIRRO",
               "NR_LATITUDE", "NR_LONGITUDE", COL_APTOS],
    obrigatorias=CHAVE_SECAO + ["NM_MUNICIPIO", "NR_LOCAL_VOTACAO", "NM_LOCAL_VOTACAO",
                                "NR_LATITUDE", "NR_LONGITUDE", COL_APTOS],
    texto=["NR_LATITUDE", "NR_LONGITUDE"],
)

print("Linhas no arquivo:", milhar(len(eleitorado_bruto)))
print("Soma bruta de aptos (sem filtro):", milhar(eleitorado_bruto[COL_APTOS].sum()))
print("Linhas repetidas na chave de seção:", milhar(eleitorado_bruto.duplicated(CHAVE_SECAO).sum()))

if "NR_TURNO" in eleitorado_bruto.columns:
    print("\nDistribuição por turno:")
    display(eleitorado_bruto.groupby("NR_TURNO")[COL_APTOS].agg(linhas="size", aptos="sum"))

Linhas no arquivo: 1.034.358
Soma bruta de aptos (sem filtro): 317.491.004
Linhas repetidas na chave de seção: 517.179

Distribuição por turno:


,linhas,aptos
NR_TURNO,,
1,517179,158745502
2,517179,158745502


In [5]:
# --- Correção 1: manter somente o turno analisado ---------------------------
eleitorado = eleitorado_bruto
if "NR_TURNO" in eleitorado.columns:
    eleitorado = eleitorado[eleitorado["NR_TURNO"] == TURNO]
eleitorado = eleitorado.drop(columns=["NR_TURNO", "DT_ELEICAO"], errors="ignore").copy()

# --- Rede de segurança: a chave de seção precisa ser única ------------------
repetidas = eleitorado.duplicated(CHAVE_SECAO, keep=False)
if repetidas.any():
    grupo = eleitorado[repetidas].groupby(CHAVE_SECAO)
    variam = [c for c in eleitorado.columns if c not in CHAVE_SECAO
              and (grupo[c].nunique(dropna=False) > 1).any()]
    print(f"ATENÇÃO: {milhar(repetidas.sum())} linhas ainda repetem a chave de seção "
          f"após o filtro de turno. Colunas que variam entre as cópias: {variam}")
    print("Mantida a primeira ocorrência de cada seção — confira o total com o TSE.")
    eleitorado = eleitorado.drop_duplicates(CHAVE_SECAO, keep="first").copy()

assert not eleitorado.duplicated(CHAVE_SECAO).any(), "Seção duplicada no eleitorado"

# Coordenadas: vírgula decimal -> ponto
for c in ["NR_LATITUDE", "NR_LONGITUDE"]:
    eleitorado[c] = pd.to_numeric(
        eleitorado[c].astype(str).str.replace(",", ".", regex=False), errors="coerce")

APTOS_TOTAL = int(eleitorado[COL_APTOS].sum())
print("Seções únicas:", milhar(len(eleitorado)))
print("Eleitores aptos (1.º turno):", milhar(APTOS_TOTAL))

Seções únicas: 517.179
Eleitores aptos (1.º turno): 158.745.502


## 4. Votação por seção (comparecimento)

In [6]:
votos = ler_csv_tse(
    zf_votos, ARQ_VOTOS,
    desejadas=["NR_TURNO", "CD_CARGO", "DS_CARGO", "SG_UF", "CD_MUNICIPIO", "NM_MUNICIPIO",
               "NR_ZONA", "NR_SECAO", "NR_LOCAL_VOTACAO", "NM_LOCAL_VOTACAO",
               "NM_VOTAVEL", "QT_VOTOS"],
    obrigatorias=CHAVE_SECAO + ["NM_VOTAVEL", "QT_VOTOS"],
)
print("Linhas no arquivo:", milhar(len(votos)))

if "NR_TURNO" in votos.columns:
    print("Turnos presentes:", sorted(votos["NR_TURNO"].unique().tolist()))
    votos = votos[votos["NR_TURNO"] == TURNO]
if "DS_CARGO" in votos.columns:
    print("Cargos presentes:", votos["DS_CARGO"].drop_duplicates().tolist())
    votos = votos[votos["DS_CARGO"].str.upper().str.strip() == "PRESIDENTE"]
votos = votos.copy()
votos["NM_VOTAVEL"] = votos["NM_VOTAVEL"].str.strip()

if votos.empty:
    raise ValueError("Nenhum voto para Presidente no turno selecionado.")

# Uma linha por seção x votável; linhas idênticas indicariam arquivo duplicado.
rep = votos.duplicated(CHAVE_SECAO + ["NM_VOTAVEL"]).sum()
if rep:
    print(f"ATENÇÃO: {milhar(rep)} linhas repetidas (seção x votável) no arquivo de votação.")

BRANCO_NULO = ["VOTO BRANCO", "VOTO NULO"]
CANDIDATOS = sorted(v for v in votos["NM_VOTAVEL"].unique() if v not in BRANCO_NULO)
COMPARECIMENTO_TOTAL = int(votos["QT_VOTOS"].sum())

print("\nCandidatos:", CANDIDATOS)
print("Comparecimento (votos para Presidente):", milhar(COMPARECIMENTO_TOTAL))

Linhas no arquivo: 3.800.511
Turnos presentes: [1]
Cargos presentes: ['Presidente']

Candidatos: ['AUGUSTO JORGE CURY', 'CLARIANA ZACARKIM BARAO', 'EDMILSON SILVA COSTA', 'FLAVIO NANTES BOLSONARO', 'HERTZ DA CONCEICAO DIAS', 'LEONARDO ALVES DE ARAUJO', 'LUIZ INÁCIO LULA DA SILVA', 'RENAN ANTONIO FERREIRA DOS SANTOS', 'ROMEU ZEMA NETO', 'RONALDO RAMOS CAIADO', 'RUI COSTA PIMENTA', 'SAMARA MARTINS DA SILVA FEITOSA', 'WILSON GRASSI JUNIOR']
Comparecimento (votos para Presidente): 125.275.835


## 5. Resumo nacional

Os dois totais vêm **diretamente de cada arquivo**, sem `merge` — por isso não podem ser inflados
nem reduzidos por problemas de junção.

In [7]:
ABSTENCAO_TOTAL = APTOS_TOTAL - COMPARECIMENTO_TOTAL
TAXA_NACIONAL = round(100 * ABSTENCAO_TOTAL / APTOS_TOTAL, 2)

resumo_nacional = pd.DataFrame({
    "Calculado": {"Aptos": APTOS_TOTAL, "Comparecimento": COMPARECIMENTO_TOTAL,
                  "Abstenção": ABSTENCAO_TOTAL, "Taxa (%)": TAXA_NACIONAL},
    "Oficial TSE": REFERENCIA_TSE,
})
resumo_nacional["Diferença"] = resumo_nacional["Calculado"] - resumo_nacional["Oficial TSE"]

print(f"ELEIÇÃO {ANO} — {TURNO}.º TURNO — PRESIDENTE\n")
print("Eleitores aptos :", milhar(APTOS_TOTAL))
print("Comparecimento  :", milhar(COMPARECIMENTO_TOTAL))
print("Abstenções      :", milhar(ABSTENCAO_TOTAL))
print("Taxa de abstenção:", pct(TAXA_NACIONAL))
display(formatar_resumo(resumo_nacional))

votacao_nacional = votos.groupby("NM_VOTAVEL")["QT_VOTOS"].sum().sort_values(ascending=False).to_frame("VOTOS")
validos = votacao_nacional.loc[votacao_nacional.index.isin(CANDIDATOS), "VOTOS"].sum()
votacao_nacional["PCT_VALIDOS"] = np.where(
    votacao_nacional.index.isin(CANDIDATOS), (100 * votacao_nacional["VOTOS"] / validos).round(2), np.nan)
display(votacao_nacional)

ELEIÇÃO 2026 — 1.º TURNO — PRESIDENTE

Eleitores aptos : 158.745.502
Comparecimento  : 125.275.835
Abstenções      : 33.469.667
Taxa de abstenção: 21,08%


,Calculado,Oficial TSE,Diferença
Aptos,158.745.502,158.745.502,0
Comparecimento,125.275.835,125.275.835,0
Abstenção,33.469.667,33.469.244,423
Taxa (%),"21,08","21,08","0,00"


,VOTOS,PCT_VALIDOS
NM_VOTAVEL,,
FLAVIO NANTES BOLSONARO,56104503,47.03
LUIZ INÁCIO LULA DA SILVA,53879538,45.16
VOTO NULO,3669003,NaN
AUGUSTO JORGE CURY,3448569,2.89
RENAN ANTONIO FERREIRA DOS SANTOS,2675887,2.24
RONALDO RAMOS CAIADO,2605148,2.18
VOTO BRANCO,2300798,NaN
ROMEU ZEMA NETO,326488,0.27
SAMARA MARTINS DA SILVA FEITOSA,122911,0.10


## 6. Conciliação seção a seção

A junção usa **somente a chave numérica da seção**. O nome do local (`NM_LOCAL_VOTACAO`) não entra
na chave: qualquer diferença de grafia entre os dois arquivos descartava votos silenciosamente.

In [8]:
comp_secao = (votos.groupby(CHAVE_SECAO, as_index=False)["QT_VOTOS"].sum()
              .rename(columns={"QT_VOTOS": "COMPARECIMENTO"}))

secoes = eleitorado.merge(comp_secao, on=CHAVE_SECAO, how="outer",
                          validate="one_to_one", indicator="ORIGEM")
secoes["ORIGEM"] = secoes["ORIGEM"].map({"both": "nos dois arquivos",
                                         "left_only": "só no eleitorado (sem votos)",
                                         "right_only": "só na votação (sem eleitorado)"})

conciliacao = secoes.groupby("ORIGEM", observed=True).agg(
    secoes=("NR_SECAO", "size"), aptos=(COL_APTOS, "sum"), comparecimento=("COMPARECIMENTO", "sum"))
display(conciliacao)

if "DS_TIPO_SECAO_AGREGADA" in secoes.columns:
    print("Seções com eleitorado e sem votos, por tipo de agregação:")
    display(secoes[secoes["ORIGEM"] == "só no eleitorado (sem votos)"]
            .groupby("DS_TIPO_SECAO_AGREGADA", dropna=False)[COL_APTOS].agg(secoes="size", aptos="sum"))

,secoes,aptos,comparecimento
ORIGEM,,,
só no eleitorado (sem votos),17973,495,0.0
nos dois arquivos,499206,158745007,125275835.0


Seções com eleitorado e sem votos, por tipo de agregação:


,secoes,aptos
DS_TIPO_SECAO_AGREGADA,,
Agregada,17931,0
Principal,42,495


In [9]:
# Tabela por seção (somente seções que constam no eleitorado)
abstencao_secao = secoes[secoes[COL_APTOS].notna()].drop(columns="ORIGEM").copy()
abstencao_secao["COMPARECIMENTO"] = abstencao_secao["COMPARECIMENTO"].fillna(0).astype("int64")
abstencao_secao[COL_APTOS] = abstencao_secao[COL_APTOS].astype("int64")
abstencao_secao["ABSTENCAO"] = abstencao_secao[COL_APTOS] - abstencao_secao["COMPARECIMENTO"]
abstencao_secao["PCT_ABSTENCAO"] = (100 * abstencao_secao["ABSTENCAO"]
                                    / abstencao_secao[COL_APTOS].where(abstencao_secao[COL_APTOS] > 0)).round(2)

assert abstencao_secao[COL_APTOS].sum() == APTOS_TOTAL
print("Seções:", milhar(len(abstencao_secao)))
print("Seções com comparecimento maior que aptos:",
      milhar((abstencao_secao["COMPARECIMENTO"] > abstencao_secao[COL_APTOS]).sum()))
display(abstencao_secao.head())

Seções: 517.179
Seções com comparecimento maior que aptos: 0


,SG_UF,CD_MUNICIPIO,NM_MUNICIPIO,NR_ZONA,NR_SECAO,DS_TIPO_SECAO_AGREGADA,NR_SECAO_PRINCIPAL,NR_LOCAL_VOTACAO,NM_LOCAL_VOTACAO,DS_ENDERECO,NM_BAIRRO,NR_LATITUDE,NR_LONGITUDE,QT_ELEITOR_ELEICAO_FEDERAL,COMPARECIMENTO,ABSTENCAO,PCT_ABSTENCAO
0,AC,1007,BUJARI,9,1,Principal,-1,1104,ESCOLA EDMUNDO PINTO DE ALMEIDA NETO,RUA NEUTEL MAIA,CENTRO,-9.824693,-67.951288,308,241,67,21.75
1,AC,1007,BUJARI,9,2,Principal,-1,1104,ESCOLA EDMUNDO PINTO DE ALMEIDA NETO,RUA NEUTEL MAIA,CENTRO,-9.824693,-67.951288,308,240,68,22.08
2,AC,1007,BUJARI,9,3,Principal,-1,1104,ESCOLA EDMUNDO PINTO DE ALMEIDA NETO,RUA NEUTEL MAIA,CENTRO,-9.824693,-67.951288,303,242,61,20.13
3,AC,1007,BUJARI,9,4,Principal,-1,1104,ESCOLA EDMUNDO PINTO DE ALMEIDA NETO,RUA NEUTEL MAIA,CENTRO,-9.824693,-67.951288,303,244,59,19.47
4,AC,1007,BUJARI,9,5,Principal,-1,1112,ESCOLA SÃO JOÃO BATISTA,"RUA JOSÉ PEREIRA GURGEL, 835",CENTRO,-9.824765,-67.949660,328,251,77,23.48


## 7. Abstenção por local de votação

Cada seção (e seus votos) é atribuída ao local informado no cadastro do eleitorado.
Seções agregadas sem votos próprios são levadas para o local da seção principal, onde os votos foram apurados.

In [10]:
# --- seção -> local de votação ----------------------------------------------
mapa_secao = eleitorado[CHAVE_SECAO + ["NR_LOCAL_VOTACAO"]].copy()

if "NR_SECAO_PRINCIPAL" in eleitorado.columns:
    sem_votos = ~mapa_secao.set_index(CHAVE_SECAO).index.isin(comp_secao.set_index(CHAVE_SECAO).index)
    principal = pd.to_numeric(eleitorado["NR_SECAO_PRINCIPAL"], errors="coerce")
    agregada = sem_votos & principal.notna().values & (principal.values != eleitorado["NR_SECAO"].values)
    if agregada.any():
        local_da_principal = (
            eleitorado.loc[agregada, ["SG_UF", "CD_MUNICIPIO", "NR_ZONA"]]
            .assign(NR_SECAO=principal[agregada].astype("int64").values)
            .merge(mapa_secao, on=CHAVE_SECAO, how="left")["NR_LOCAL_VOTACAO"].values)
        atual = mapa_secao.loc[agregada, "NR_LOCAL_VOTACAO"].values
        mapa_secao.loc[agregada, "NR_LOCAL_VOTACAO"] = np.where(
            pd.notna(local_da_principal), local_da_principal, atual).astype(atual.dtype)
        print("Seções agregadas realocadas para o local da seção principal:",
              milhar((pd.notna(local_da_principal) & (local_da_principal != atual)).sum()))

# --- aptos por local -----------------------------------------------------------
aptos_local = (eleitorado[CHAVE_SECAO + [COL_APTOS]]
               .merge(mapa_secao, on=CHAVE_SECAO, validate="one_to_one")
               .groupby(CHAVE_LOCAL, as_index=False)
               .agg(**{COL_APTOS: (COL_APTOS, "sum"), "QT_SECOES": ("NR_SECAO", "size")}))

# --- votos por local e por votável --------------------------------------------
v = votos.rename(columns={"NR_LOCAL_VOTACAO": "NR_LOCAL_VOTOS"}).merge(
    mapa_secao, on=CHAVE_SECAO, how="left", validate="many_to_one")
if "NR_LOCAL_VOTOS" in v.columns:      # seção ausente do eleitorado: usa o local do arquivo de votação
    v["NR_LOCAL_VOTACAO"] = v["NR_LOCAL_VOTACAO"].fillna(v["NR_LOCAL_VOTOS"])
sem_local = v["NR_LOCAL_VOTACAO"].isna()
VOTOS_SEM_LOCAL = int(v.loc[sem_local, "QT_VOTOS"].sum())
if VOTOS_SEM_LOCAL:
    print("Votos sem local identificável (ficam fora da tabela por local):", milhar(VOTOS_SEM_LOCAL))
v = v[~sem_local].copy()
v["NR_LOCAL_VOTACAO"] = v["NR_LOCAL_VOTACAO"].astype("int64")

votos_wide = (v.pivot_table(index=CHAVE_LOCAL, columns="NM_VOTAVEL", values="QT_VOTOS",
                            aggfunc="sum", fill_value=0)
              .reindex(columns=CANDIDATOS + BRANCO_NULO, fill_value=0)
              .reset_index())
votos_wide.columns.name = None
COLS_VOTO = CANDIDATOS + BRANCO_NULO

# --- atributos do local (nome, endereço, coordenadas) ---------------------------
atributos = ["NM_MUNICIPIO", "NM_LOCAL_VOTACAO", "DS_ENDERECO", "NM_BAIRRO", "NR_LATITUDE", "NR_LONGITUDE"]
atributos = [c for c in atributos if c in eleitorado.columns]
info_local = eleitorado.groupby(CHAVE_LOCAL, as_index=False)[atributos].first()

# --- tabela final por local ---------------------------------------------------------
abstencao_local = (aptos_local.merge(votos_wide, on=CHAVE_LOCAL, how="outer", validate="one_to_one")
                   .merge(info_local, on=CHAVE_LOCAL, how="left", validate="one_to_one"))

# locais que só existem no arquivo de votação: aproveita os nomes desse arquivo
for col in ["NM_MUNICIPIO", "NM_LOCAL_VOTACAO"]:
    if col in votos.columns and abstencao_local[col].isna().any():
        chave = CHAVE_LOCAL if col == "NM_LOCAL_VOTACAO" else ["SG_UF", "CD_MUNICIPIO"]
        ref = votos.drop_duplicates(chave)[chave + [col]].rename(columns={col: col + "_V"})
        abstencao_local = abstencao_local.merge(ref, on=chave, how="left")
        abstencao_local[col] = abstencao_local[col].fillna(abstencao_local.pop(col + "_V"))

num = [COL_APTOS, "QT_SECOES"] + COLS_VOTO
abstencao_local[num] = abstencao_local[num].fillna(0).astype("int64")

abstencao_local["COMPARECIMENTO"] = abstencao_local[COLS_VOTO].sum(axis=1)
abstencao_local["VOTOS_VALIDOS"] = abstencao_local[CANDIDATOS].sum(axis=1)
abstencao_local["ABSTENCAO"] = abstencao_local[COL_APTOS] - abstencao_local["COMPARECIMENTO"]
abstencao_local["PCT_ABSTENCAO"] = (100 * abstencao_local["ABSTENCAO"]
                                    / abstencao_local[COL_APTOS].where(abstencao_local[COL_APTOS] > 0)).round(2)
abstencao_local["INCONSISTENTE"] = abstencao_local["COMPARECIMENTO"] > abstencao_local[COL_APTOS]

# --- resultado da disputa em cada local ------------------------------------------
col_lula = next(c for c in CANDIDATOS if "LULA" in c.upper())
col_bol = next(c for c in CANDIDATOS if "BOLSONARO" in c.upper())
validos_local = abstencao_local["VOTOS_VALIDOS"].where(abstencao_local["VOTOS_VALIDOS"] > 0)
abstencao_local["PCT_LULA"] = (100 * abstencao_local[col_lula] / validos_local).round(2)
abstencao_local["PCT_BOLSONARO"] = (100 * abstencao_local[col_bol] / validos_local).round(2)
abstencao_local["MARGEM"] = (abstencao_local["PCT_LULA"] - abstencao_local["PCT_BOLSONARO"]).round(2)

maior = abstencao_local[CANDIDATOS].max(axis=1)
empate = abstencao_local[CANDIDATOS].eq(maior, axis=0).sum(axis=1) > 1
abstencao_local["VENCEDOR"] = abstencao_local[CANDIDATOS].idxmax(axis=1)
abstencao_local.loc[empate, "VENCEDOR"] = "EMPATE"
abstencao_local.loc[abstencao_local["VOTOS_VALIDOS"] == 0, "VENCEDOR"] = "SEM VOTOS VÁLIDOS"

ordem = (CHAVE_LOCAL[:2] + ["NM_MUNICIPIO", "NR_ZONA", "NR_LOCAL_VOTACAO"]
         + [c for c in atributos if c != "NM_MUNICIPIO"]
         + ["QT_SECOES", COL_APTOS, "COMPARECIMENTO", "ABSTENCAO", "PCT_ABSTENCAO", "INCONSISTENTE",
            "VOTOS_VALIDOS"] + COLS_VOTO + ["PCT_LULA", "PCT_BOLSONARO", "MARGEM", "VENCEDOR"])
abstencao_local = abstencao_local[ordem].sort_values(CHAVE_LOCAL).reset_index(drop=True)

print("Locais de votação:", milhar(len(abstencao_local)))
print("Lula:", col_lula, "| Bolsonaro:", col_bol)
display(abstencao_local.head())

Seções agregadas realocadas para o local da seção principal: 2.074
Locais de votação: 94.299
Lula: LUIZ INÁCIO LULA DA SILVA | Bolsonaro: FLAVIO NANTES BOLSONARO


,SG_UF,CD_MUNICIPIO,NM_MUNICIPIO,NR_ZONA,NR_LOCAL_VOTACAO,NM_LOCAL_VOTACAO,DS_ENDERECO,NM_BAIRRO,NR_LATITUDE,NR_LONGITUDE,...,RONALDO RAMOS CAIADO,RUI COSTA PIMENTA,SAMARA MARTINS DA SILVA FEITOSA,WILSON GRASSI JUNIOR,VOTO BRANCO,VOTO NULO,PCT_LULA,PCT_BOLSONARO,MARGEM,VENCEDOR
0,AC,1007,BUJARI,9,1023,ESCOLA JOSE CEZARIO DE FARIAS,BR 364 KM 50 ESTRADA DE SENA MADUREIRA S/N,ZONA RURAL,-9.726385,-68.124095,...,13,0,1,0,17,37,26.24,70.13,-43.89,FLAVIO NANTES BOLSONARO
1,AC,1007,BUJARI,9,1040,ESCOLA MAPINGUARI - FUNTAC - PROJETO ANTIMARI,BR-364 KM-86 PONTE DO RIO ANTIMARI - DESCENDO ...,ZONA RURAL,-9.403595,-68.143584,...,0,0,0,0,1,2,9.80,88.89,-79.09,FLAVIO NANTES BOLSONARO
2,AC,1007,BUJARI,9,1058,"NÚCLEO DE EDUCAÇÃO, CULTURA E ESPORTES - SEE -...","RUA RAIO DE SOL, S/N",CENTRO,-9.826678,-67.951138,...,15,0,0,0,6,17,31.03,63.75,-32.72,FLAVIO NANTES BOLSONARO
3,AC,1007,BUJARI,9,1066,ESCOLA RURAL NOVA VIDA,BR 346 KM 52 RAMAL DO ESPINHARA KM 15,ZONA RURAL,-9.643802,-68.042748,...,5,0,0,0,5,9,39.61,55.96,-16.35,FLAVIO NANTES BOLSONARO
4,AC,1007,BUJARI,9,1074,ESCOLA RURAL MARIA DO CARMO RAMOS,BR 346 KM 52 RAMAL LINHA NOVA KM 18,ZONA RURAL,-9.793075,-68.260456,...,4,0,0,0,0,7,9.60,87.20,-77.60,FLAVIO NANTES BOLSONARO


### Validação: os locais precisam somar exatamente o total nacional

In [11]:
soma_aptos = int(abstencao_local[COL_APTOS].sum())
soma_comp = int(abstencao_local["COMPARECIMENTO"].sum())
soma_abst = int(abstencao_local["ABSTENCAO"].sum())

validacao = pd.DataFrame({
    "Nacional (arquivos)": [APTOS_TOTAL, COMPARECIMENTO_TOTAL, ABSTENCAO_TOTAL],
    "Soma dos locais": [soma_aptos, soma_comp, soma_abst],
}, index=["Aptos", "Comparecimento", "Abstenção"])
validacao["Diferença"] = validacao["Soma dos locais"] - validacao["Nacional (arquivos)"]
# (diferença só é admitida se houver votos sem local identificável, informados na célula anterior)
display(validacao)

assert not abstencao_local.duplicated(CHAVE_LOCAL).any(), "Local de votação duplicado"
assert soma_aptos == APTOS_TOTAL, "Aptos por local não fecham com o total nacional"
assert soma_comp == COMPARECIMENTO_TOTAL - VOTOS_SEM_LOCAL, \
    "Comparecimento por local não fecha com o total nacional"

print("Locais com comparecimento maior que aptos:", milhar(abstencao_local["INCONSISTENTE"].sum()))
print("Locais sem eleitorado cadastrado          :", milhar((abstencao_local[COL_APTOS] == 0).sum()))
print("\nVALIDAÇÃO OK — sem duplicidade e totais fechados.")

,Nacional (arquivos),Soma dos locais,Diferença
Aptos,158745502,158745502,0
Comparecimento,125275835,125275835,0
Abstenção,33469667,33469667,0


Locais com comparecimento maior que aptos: 0
Locais sem eleitorado cadastrado          : 0

VALIDAÇÃO OK — sem duplicidade e totais fechados.


## 8. Resumos por UF e por município

In [12]:
def resumir(df, chaves):
    r = df.groupby(chaves, as_index=False).agg(
        LOCAIS=("NR_LOCAL_VOTACAO", "size"),
        **{COL_APTOS: (COL_APTOS, "sum")},
        COMPARECIMENTO=("COMPARECIMENTO", "sum"),
        ABSTENCAO=("ABSTENCAO", "sum"),
        **{c: (c, "sum") for c in COLS_VOTO})
    r.insert(r.columns.get_loc("ABSTENCAO") + 1, "PCT_ABSTENCAO",
             (100 * r["ABSTENCAO"] / r[COL_APTOS].where(r[COL_APTOS] > 0)).round(2))
    return r


abstencao_uf = resumir(abstencao_local, ["SG_UF"]).sort_values("PCT_ABSTENCAO", ascending=False)
abstencao_municipio = resumir(abstencao_local, ["SG_UF", "CD_MUNICIPIO", "NM_MUNICIPIO"])

assert abstencao_uf[COL_APTOS].sum() == APTOS_TOTAL
display(abstencao_uf[["SG_UF", "LOCAIS", COL_APTOS, "COMPARECIMENTO", "ABSTENCAO", "PCT_ABSTENCAO"]]
        .reset_index(drop=True))

,SG_UF,LOCAIS,QT_ELEITOR_ELEICAO_FEDERAL,COMPARECIMENTO,ABSTENCAO,PCT_ABSTENCAO
0,ZZ,212,916534,341766,574768,62.71
1,MS,1021,2024430,1541220,483210,23.87
2,RJ,5046,12857648,9859802,2997846,23.32
3,MG,10073,16372372,12637274,3735098,22.81
4,SP,11072,34122892,26431992,7690900,22.54
5,MT,1501,2637801,2052133,585668,22.20
6,GO,2476,5080590,3971587,1109003,21.83
7,RO,671,1265893,991080,274813,21.71
8,ES,1765,2991650,2352282,639368,21.37
9,RS,7772,8522545,6702903,1819642,21.35


### Exemplo de consulta por UF (altere `UF_EXEMPLO` na configuração)

In [18]:
UF_EXEMPLO = "PA"

df_uf = abstencao_local[abstencao_local["SG_UF"] == UF_EXEMPLO]
display(df_uf[["NM_MUNICIPIO", "NR_ZONA", "NM_LOCAL_VOTACAO", COL_APTOS,
               "COMPARECIMENTO", "ABSTENCAO", "PCT_ABSTENCAO"]]
        .sort_values(COL_APTOS, ascending=False).head(50))


df_uf = abstencao_local[abstencao_local["SG_UF"] == UF_EXEMPLO]
display(df_uf[["NM_MUNICIPIO", "NR_ZONA", "NM_LOCAL_VOTACAO", COL_APTOS,
               "COMPARECIMENTO", "ABSTENCAO", "PCT_ABSTENCAO"]]
        .sort_values(COL_APTOS, ascending=False).head(50))

,NM_MUNICIPIO,NR_ZONA,NM_LOCAL_VOTACAO,QT_ELEITOR_ELEICAO_FEDERAL,COMPARECIMENTO,ABSTENCAO,PCT_ABSTENCAO
44042,BELÉM,29,UNIVERSIDADE FEDERAL DO PARÁ,12187,10421,1766,14.49
43544,ANANINDEUA,72,EEEFM LUIZ NUNES DIREITO,11203,9276,1927,17.20
44343,BELÉM,98,FACULDADE COSMOPOLITA,10361,8586,1775,17.13
44014,BELÉM,28,EEEFM JOSÉ ALVES MAIA,8440,7012,1428,16.92
44245,BELÉM,96,EEEF BRIGADEIRO FONTENELLE,8430,7005,1425,16.90
44010,BELÉM,28,EERCF SANTO AFONSO,8193,6752,1441,17.59
43991,BELÉM,1,EEEFM PROF CAMILO SALGADO,8006,6866,1140,14.24
44295,BELÉM,97,LICEU DE ARTES E OFÍCIOS MESTRE RAIMUNDO CARDOSO,7759,6257,1502,19.36
44144,BELÉM,73,EEEFM MARIA LUIZA DA COSTA REGO,7693,6104,1589,20.66
43557,ANANINDEUA,72,EEEFM JORNALISTA RÔMULO MAIORANA,7604,6252,1352,17.78


,NM_MUNICIPIO,NR_ZONA,NM_LOCAL_VOTACAO,QT_ELEITOR_ELEICAO_FEDERAL,COMPARECIMENTO,ABSTENCAO,PCT_ABSTENCAO
44042,BELÉM,29,UNIVERSIDADE FEDERAL DO PARÁ,12187,10421,1766,14.49
43544,ANANINDEUA,72,EEEFM LUIZ NUNES DIREITO,11203,9276,1927,17.20
44343,BELÉM,98,FACULDADE COSMOPOLITA,10361,8586,1775,17.13
44014,BELÉM,28,EEEFM JOSÉ ALVES MAIA,8440,7012,1428,16.92
44245,BELÉM,96,EEEF BRIGADEIRO FONTENELLE,8430,7005,1425,16.90
44010,BELÉM,28,EERCF SANTO AFONSO,8193,6752,1441,17.59
43991,BELÉM,1,EEEFM PROF CAMILO SALGADO,8006,6866,1140,14.24
44295,BELÉM,97,LICEU DE ARTES E OFÍCIOS MESTRE RAIMUNDO CARDOSO,7759,6257,1502,19.36
44144,BELÉM,73,EEEFM MARIA LUIZA DA COSTA REGO,7693,6104,1589,20.66
43557,ANANINDEUA,72,EEEFM JORNALISTA RÔMULO MAIORANA,7604,6252,1352,17.78


## 9. Exportação das tabelas

In [19]:
abstencao_local.to_csv(CSV / "abstencao_por_local.csv", index=False, encoding="utf-8-sig")
abstencao_secao.to_csv(CSV / "abstencao_por_secao.csv", index=False, encoding="utf-8-sig")
abstencao_municipio.to_csv(CSV / "abstencao_por_municipio.csv", index=False, encoding="utf-8-sig")
abstencao_uf.to_csv(CSV / "abstencao_por_uf.csv", index=False, encoding="utf-8-sig")

with pd.ExcelWriter(CSV / "abstencao_2026_1turno.xlsx") as xl:
    resumo_nacional.to_excel(xl, sheet_name="Brasil")
    abstencao_uf.to_excel(xl, sheet_name="UF", index=False)
    abstencao_municipio.to_excel(xl, sheet_name="Municipios", index=False)
    abstencao_local.to_excel(xl, sheet_name="Locais", index=False)

for arq in sorted(CSV.iterdir()):
    print(f"{arq.name:40s} {arq.stat().st_size / 1024 / 1024:8.2f} MB")

abstencao_2026_1turno.xlsx                  19.39 MB
abstencao_por_local.csv                     21.98 MB
abstencao_por_municipio.csv                  0.50 MB
abstencao_por_secao.csv                     81.55 MB
abstencao_por_uf.csv                         0.00 MB


## 10. Base do mapa

Entram no mapa os locais com eleitorado e coordenadas dentro do território brasileiro.
O que fica de fora é listado abaixo, com o eleitorado correspondente — essas exclusões
valem **apenas para o mapa**; as tabelas e os totais continuam completos.

In [20]:
lat, lon = abstencao_local["NR_LATITUDE"], abstencao_local["NR_LONGITUDE"]
no_brasil = lat.between(-34, 6) & lon.between(-75, -32)

motivo = np.select(
    [abstencao_local[COL_APTOS] == 0,
     abstencao_local["SG_UF"] == "ZZ",
     lat.isna() | lon.isna(),
     ~no_brasil],
    ["sem eleitorado cadastrado", "exterior (ZZ)", "sem coordenadas", "coordenadas fora do Brasil"],
    default="no mapa")

display(abstencao_local.assign(SITUACAO=motivo).groupby("SITUACAO")
        .agg(locais=("NR_LOCAL_VOTACAO", "size"), aptos=(COL_APTOS, "sum"), abstencao=("ABSTENCAO", "sum")))

mapa_final = abstencao_local[motivo == "no mapa"].copy()
print("Locais no mapa:", milhar(len(mapa_final)),
      f"({pct(100 * mapa_final[COL_APTOS].sum() / APTOS_TOTAL)} do eleitorado)")

,locais,aptos,abstencao
SITUACAO,,,
coordenadas fora do Brasil,552,463031,90321
exterior (ZZ),212,916534,574768
no mapa,93535,157365937,32804578


Locais no mapa: 93.535 (99,13% do eleitorado)


## 11. GeoJSON (completo e leve, para publicação)

In [21]:
def gerar_geojson(df, caminho, leve=False):
    casas = 5 if leve else 7
    feicoes = []
    for d in df.to_dict("records"):
        if leve:
            prop = {"esc": d["NM_LOCAL_VOTACAO"], "mun": d["NM_MUNICIPIO"], "uf": d["SG_UF"],
                    "apt": int(d[COL_APTOS]), "abs": int(d["ABSTENCAO"]),
                    "pct": round(float(d["PCT_ABSTENCAO"]), 1),
                    "lul": int(d[col_lula]), "bol": int(d[col_bol])}
        else:
            bairro = d.get("NM_BAIRRO")
            prop = {"escola": d["NM_LOCAL_VOTACAO"], "municipio": d["NM_MUNICIPIO"], "uf": d["SG_UF"],
                    "zona": int(d["NR_ZONA"]), "local": int(d["NR_LOCAL_VOTACAO"]),
                    "bairro": None if pd.isna(bairro) else bairro,
                    "aptos": int(d[COL_APTOS]), "comparecimento": int(d["COMPARECIMENTO"]),
                    "abstencao": int(d["ABSTENCAO"]),
                    "pct_abstencao": round(float(d["PCT_ABSTENCAO"]), 2),
                    "lula": int(d[col_lula]), "bolsonaro": int(d[col_bol]),
                    "branco": int(d["VOTO BRANCO"]), "nulo": int(d["VOTO NULO"]),
                    "vencedor": d["VENCEDOR"]}
        feicoes.append({"type": "Feature",
                        "geometry": {"type": "Point",
                                     "coordinates": [round(float(d["NR_LONGITUDE"]), casas),
                                                     round(float(d["NR_LATITUDE"]), casas)]},
                        "properties": prop})
    with open(caminho, "w", encoding="utf-8") as f:
        json.dump({"type": "FeatureCollection", "features": feicoes}, f,
                  ensure_ascii=False, separators=(",", ":"))
    print(f"{Path(caminho).name}: {len(feicoes)} locais, {os.path.getsize(caminho) / 1024 / 1024:.2f} MB")
    return feicoes


feicoes = gerar_geojson(mapa_final, MAPAS / "escolas.geojson")
_ = gerar_geojson(mapa_final, MAPAS / "escolas_leve.geojson", leve=True)
feicoes[0]

escolas.geojson: 93535 locais, 34.92 MB
escolas_leve.geojson: 93535 locais, 19.90 MB


{'type': 'Feature',
 'geometry': {'type': 'Point', 'coordinates': [-68.1240952, -9.7263853]},
 'properties': {'escola': 'ESCOLA JOSE CEZARIO DE FARIAS',
  'municipio': 'BUJARI',
  'uf': 'AC',
  'zona': 9,
  'local': 1023,
  'bairro': 'ZONA RURAL',
  'aptos': 1433,
  'comparecimento': 1102,
  'abstencao': 331,
  'pct_abstencao': 23.1,
  'lula': 275,
  'bolsonaro': 735,
  'branco': 17,
  'nulo': 37,
  'vencedor': 'FLAVIO NANTES BOLSONARO'}}

## 12. Mapa nacional interativo (Plotly)

In [22]:
import plotly.express as px

fig = px.scatter_geo(
    mapa_final,
    lat="NR_LATITUDE", lon="NR_LONGITUDE",
    color="PCT_ABSTENCAO",
    color_continuous_scale="YlOrRd",
    range_color=[float(mapa_final["PCT_ABSTENCAO"].quantile(0.02)),
                 float(mapa_final["PCT_ABSTENCAO"].quantile(0.98))],
    hover_name="NM_LOCAL_VOTACAO",
    hover_data={"NM_MUNICIPIO": True, "SG_UF": True, COL_APTOS: ":,",
                "COMPARECIMENTO": ":,", "ABSTENCAO": ":,", "PCT_ABSTENCAO": ":.1f",
                col_lula: ":,", col_bol: ":,", "VOTO BRANCO": ":,", "VOTO NULO": ":,",
                "NR_LATITUDE": False, "NR_LONGITUDE": False},
    labels={COL_APTOS: "Aptos", "PCT_ABSTENCAO": "% abstenção", "ABSTENCAO": "Abstenção",
            "COMPARECIMENTO": "Comparecimento", "NM_MUNICIPIO": "Município", "SG_UF": "UF"},
    opacity=0.7,
    title=f"Abstenção por local de votação — {TURNO}.º turno {ANO} — Brasil: {pct(TAXA_NACIONAL)}",
)
fig.update_traces(marker={"size": 4})
fig.update_geos(scope="south america", showcountries=True, showland=True,
                landcolor="rgb(240,240,240)", lataxis_range=[-34, 6], lonaxis_range=[-75, -32])
fig.update_layout(height=900, margin={"l": 0, "r": 0, "t": 50, "b": 0})

fig.write_html(MAPAS / "mapa_abstencao_interativo.html", include_plotlyjs="cdn", full_html=True)
print("Mapa salvo:", MAPAS / "mapa_abstencao_interativo.html")
fig.show()

Mapa salvo: /content/tse2026/mapas/mapa_abstencao_interativo.html


## 13. Mapa Folium nacional (arquivo único)

Cor = faixa de abstenção; tamanho do círculo = eleitorado do local. Os pontos são agrupados e se
abrem conforme o zoom. Os marcadores são desenhados pelo navegador a partir de uma tabela compacta,
o que mantém o arquivo único leve o bastante para abrir com dezenas de milhares de locais.

`mapa_folium()` gera o país inteiro; `mapa_folium("DF")` gera apenas uma UF.

In [26]:
try:
    import folium
except ImportError:
    import subprocess, sys
    subprocess.check_call([sys.executable, "-m", "pip", "install", "-q", "folium"])
    import folium
from folium.plugins import FastMarkerCluster

FAIXAS = [(15, "#ffffb2", "até 15%"), (20, "#fecc5c", "15% a 20%"), (25, "#fd8d3c", "20% a 25%"),
          (30, "#f03b20", "25% a 30%"), (None, "#bd0026", "acima de 30%")]

# Função JavaScript que desenha cada local. Colunas da linha:
# 0 lat, 1 lon, 2 local, 3 município/UF e zona, 4 aptos, 5 comparecimento, 6 abstenção,
# 7 % abstenção, 8 Lula, 9 Bolsonaro, 10 brancos, 11 nulos
_limites = ", ".join(f"[{lim}, '{cor}']" for lim, cor, _ in FAIXAS if lim is not None)
CALLBACK_JS = f'''
function (r) {{
    var faixas = [{_limites}], cor = '{FAIXAS[-1][1]}';
    for (var i = 0; i < faixas.length; i++) {{ if (r[7] < faixas[i][0]) {{ cor = faixas[i][1]; break; }} }}
    var n = function (v) {{ return v.toLocaleString('pt-BR'); }};
    var pct = r[7].toFixed(1).replace('.', ',') + '%';
    var raio = Math.max(4, Math.min(12, Math.sqrt(r[4]) / 12));
    var m = L.circleMarker([r[0], r[1]], {{radius: raio, color: '#555', weight: 0.5,
                                           fillColor: cor, fillOpacity: 0.85}});
    m.bindTooltip(r[2] + ' — ' + pct);
    m.bindPopup('<b>' + r[2] + '</b><br>' + r[3] + '<hr>' +
                'Aptos: ' + n(r[4]) + '<br>Comparecimento: ' + n(r[5]) +
                '<br>Abstenção: ' + n(r[6]) + ' (<b>' + pct + '</b>)<hr>' +
                'Lula: ' + n(r[8]) + '<br>Bolsonaro: ' + n(r[9]) +
                '<br>Branco: ' + n(r[10]) + '<br>Nulo: ' + n(r[11]), {{maxWidth: 350}});
    return m;
}}
'''


FONTES_ESTADOS = [
    "https://raw.githubusercontent.com/codeforamerica/click_that_hood/master/public/data/brazil-states.geojson",
    "https://servicodados.ibge.gov.br/api/v3/malhas/paises/BR"
    "?formato=application/vnd.geo%2Bjson&qualidade=minima&intrarregiao=UF",
]


def contorno_estados(casas=3):
    # Contorno das 27 UFs, simplificado e guardado em disco; devolve None se não for possível obtê-lo.
    cache = MAPAS / "estados_br.geojson"
    if cache.exists():
        return json.loads(cache.read_text(encoding="utf-8"))

    def enxugar(coords):
        if isinstance(coords[0], (int, float)):
            return [round(coords[0], casas), round(coords[1], casas)]
        itens = [enxugar(c) for c in coords]
        if itens and isinstance(itens[0][0], (int, float)):        # anel: remove pontos repetidos
            itens = [p for i, p in enumerate(itens) if i == 0 or p != itens[i - 1]]
        return itens

    for url in FONTES_ESTADOS:
        try:
            r = requests.get(url, timeout=60)
            r.raise_for_status()
            bruto = r.json()
            geo = {"type": "FeatureCollection", "features": [
                {"type": "Feature", "properties": {},
                 "geometry": {"type": f["geometry"]["type"],
                              "coordinates": enxugar(f["geometry"]["coordinates"])}}
                for f in bruto["features"]]}
            cache.write_text(json.dumps(geo, separators=(",", ":")), encoding="utf-8")
            print(f"Contorno dos estados obtido ({cache.stat().st_size / 1e6:.2f} MB)")
            return geo
        except Exception as erro:
            print("Contorno dos estados indisponível nesta fonte:", type(erro).__name__)
    print("Mapa será gerado com fundo liso, sem contorno dos estados.")
    return None


def mapa_folium(uf=None):
    df = mapa_final if uf is None else mapa_final[mapa_final["SG_UF"] == uf]
    if df.empty:
        raise ValueError(f"Nenhum local no mapa para a UF {uf!r}")

    esc = lambda col: col.fillna("").astype(str).map(html.escape)
    onde = esc(df["NM_MUNICIPIO"]) + "/" + df["SG_UF"] + " — zona " + df["NR_ZONA"].astype(str)
    dados = list(zip(
        df["NR_LATITUDE"].round(5).tolist(), df["NR_LONGITUDE"].round(5).tolist(),
        esc(df["NM_LOCAL_VOTACAO"]).tolist(), onde.tolist(),
        df[COL_APTOS].tolist(), df["COMPARECIMENTO"].tolist(), df["ABSTENCAO"].tolist(),
        df["PCT_ABSTENCAO"].round(1).tolist(), df[col_lula].tolist(), df[col_bol].tolist(),
        df["VOTO BRANCO"].tolist(), df["VOTO NULO"].tolist()))
    dados = [list(linha) for linha in dados]

    m = folium.Map(location=[-15, -55] if uf is None else
                   [df["NR_LATITUDE"].median(), df["NR_LONGITUDE"].median()],
                   zoom_start=4 if uf is None else 7, tiles=None,
                   control_scale=True, prefer_canvas=True,
                   min_zoom=3, maxZoom=18)     # sem camada de imagens, o zoom máximo precisa ser explícito

    # Fundo sem serviço externo: contorno dos estados gravado dentro do próprio HTML.
    m.get_root().header.add_child(folium.Element(
        "<style>.leaflet-container{background:#dbe7ef !important;}</style>"))
    estados = contorno_estados()
    if estados is not None:
        folium.GeoJson(estados, name="Estados", interactive=False,
                       style_function=lambda f: {"color": "#8a8a8a", "weight": 1,
                                                 "fillColor": "#f7f7f5", "fillOpacity": 1}).add_to(m)

    FastMarkerCluster(dados, callback=CALLBACK_JS, name="Locais de votação",
                      options={"disableClusteringAtZoom": 14, "chunkedLoading": True}).add_to(m)

    itens = "".join(f"<div><span style='background:{c};width:12px;height:12px;display:inline-block;"
                    f"border:1px solid #555;margin-right:6px'></span>{rot}</div>" for _, c, rot in FAIXAS)
    escopo = "Brasil" if uf is None else uf
    taxa = 100 * df["ABSTENCAO"].sum() / df[COL_APTOS].sum()
    m.get_root().html.add_child(folium.Element(
        "<div style='position:fixed;bottom:30px;left:10px;z-index:9999;background:white;padding:8px 10px;"
        "border:1px solid #999;border-radius:4px;font:12px sans-serif'>"
        f"<b>% de abstenção — {TURNO}.º turno {ANO}</b>{itens}"
        f"<div style='margin-top:4px'>{escopo} (locais no mapa): {pct(taxa)}</div></div>"))

    arquivo = MAPAS / f"mapa_abstencao_{'BR' if uf is None else uf}.html"
    m.save(str(arquivo))
    print(f"Mapa salvo: {arquivo} — {milhar(len(df))} locais, {arquivo.stat().st_size / 1e6:.1f} MB")
    return m, arquivo


m, ARQ_MAPA_BR = mapa_folium()          # país inteiro, arquivo único
print("O mapa nacional não é exibido aqui dentro (pesado para o notebook): abra o arquivo HTML no navegador.")

Contorno dos estados obtido (1.45 MB)
Mapa salvo: /content/tse2026/mapas/mapa_abstencao_BR.html — 93.535 locais, 14.7 MB
O mapa nacional não é exibido aqui dentro (pesado para o notebook): abra o arquivo HTML no navegador.


In [23]:
try:
    import folium
except ImportError:
    import subprocess, sys
    subprocess.check_call([sys.executable, "-m", "pip", "install", "-q", "folium"])
    import folium
from folium.plugins import FastMarkerCluster

FAIXAS = [(15, "#ffffb2", "até 15%"), (20, "#fecc5c", "15% a 20%"), (25, "#fd8d3c", "20% a 25%"),
          (30, "#f03b20", "25% a 30%"), (None, "#bd0026", "acima de 30%")]

# Função JavaScript que desenha cada local. Colunas da linha:
# 0 lat, 1 lon, 2 local, 3 município/UF e zona, 4 aptos, 5 comparecimento, 6 abstenção,
# 7 % abstenção, 8 Lula, 9 Bolsonaro, 10 brancos, 11 nulos
_limites = ", ".join(f"[{lim}, '{cor}']" for lim, cor, _ in FAIXAS if lim is not None)
CALLBACK_JS = f'''
function (r) {{
    var faixas = [{_limites}], cor = '{FAIXAS[-1][1]}';
    for (var i = 0; i < faixas.length; i++) {{ if (r[7] < faixas[i][0]) {{ cor = faixas[i][1]; break; }} }}
    var n = function (v) {{ return v.toLocaleString('pt-BR'); }};
    var pct = r[7].toFixed(1).replace('.', ',') + '%';
    var raio = Math.max(4, Math.min(12, Math.sqrt(r[4]) / 12));
    var m = L.circleMarker([r[0], r[1]], {{radius: raio, color: '#555', weight: 0.5,
                                           fillColor: cor, fillOpacity: 0.85}});
    m.bindTooltip(r[2] + ' — ' + pct);
    m.bindPopup('<b>' + r[2] + '</b><br>' + r[3] + '<hr>' +
                'Aptos: ' + n(r[4]) + '<br>Comparecimento: ' + n(r[5]) +
                '<br>Abstenção: ' + n(r[6]) + ' (<b>' + pct + '</b>)<hr>' +
                'Lula: ' + n(r[8]) + '<br>Bolsonaro: ' + n(r[9]) +
                '<br>Branco: ' + n(r[10]) + '<br>Nulo: ' + n(r[11]), {{maxWidth: 350}});
    return m;
}}
'''


def mapa_folium(uf=None):
    df = mapa_final if uf is None else mapa_final[mapa_final["SG_UF"] == uf]
    if df.empty:
        raise ValueError(f"Nenhum local no mapa para a UF {uf!r}")

    esc = lambda col: col.fillna("").astype(str).map(html.escape)
    onde = esc(df["NM_MUNICIPIO"]) + "/" + df["SG_UF"] + " — zona " + df["NR_ZONA"].astype(str)
    dados = list(zip(
        df["NR_LATITUDE"].round(5).tolist(), df["NR_LONGITUDE"].round(5).tolist(),
        esc(df["NM_LOCAL_VOTACAO"]).tolist(), onde.tolist(),
        df[COL_APTOS].tolist(), df["COMPARECIMENTO"].tolist(), df["ABSTENCAO"].tolist(),
        df["PCT_ABSTENCAO"].round(1).tolist(), df[col_lula].tolist(), df[col_bol].tolist(),
        df["VOTO BRANCO"].tolist(), df["VOTO NULO"].tolist()))
    dados = [list(linha) for linha in dados]

    m = folium.Map(location=[-15, -55] if uf is None else
                   [df["NR_LATITUDE"].median(), df["NR_LONGITUDE"].median()],
                   zoom_start=4 if uf is None else 10, tiles="OpenStreetMap",
                   control_scale=True, prefer_canvas=True)
    FastMarkerCluster(dados, callback=CALLBACK_JS,
                      options={"disableClusteringAtZoom": 14, "chunkedLoading": True}).add_to(m)

    itens = "".join(f"<div><span style='background:{c};width:12px;height:12px;display:inline-block;"
                    f"border:1px solid #555;margin-right:6px'></span>{rot}</div>" for _, c, rot in FAIXAS)
    escopo = "Brasil" if uf is None else uf
    taxa = 100 * df["ABSTENCAO"].sum() / df[COL_APTOS].sum()
    m.get_root().html.add_child(folium.Element(
        "<div style='position:fixed;bottom:30px;left:10px;z-index:9999;background:white;padding:8px 10px;"
        "border:1px solid #999;border-radius:4px;font:12px sans-serif'>"
        f"<b>% de abstenção — {TURNO}.º turno {ANO}</b>{itens}"
        f"<div style='margin-top:4px'>{escopo} (locais no mapa): {pct(taxa)}</div></div>"))

    arquivo = MAPAS / f"mapa_abstencao_{'BR' if uf is None else uf}.html"
    m.save(str(arquivo))
    print(f"Mapa salvo: {arquivo} — {milhar(len(df))} locais, {arquivo.stat().st_size / 1e6:.1f} MB")
    return m, arquivo


m, ARQ_MAPA_BR = mapa_folium()          # país inteiro, arquivo único
print("O mapa nacional não é exibido aqui dentro (pesado para o notebook): abra o arquivo HTML no navegador.")

Mapa salvo: /content/tse2026/mapas/mapa_abstencao_BR.html — 93.535 locais, 13.1 MB
O mapa nacional não é exibido aqui dentro (pesado para o notebook): abra o arquivo HTML no navegador.


## 14. Conferência final

In [24]:
print(f"ELEIÇÃO {ANO} — {TURNO}.º TURNO — PRESIDENTE")
print("-" * 46)
print(f"Eleitores aptos   : {milhar(APTOS_TOTAL):>15}")
print(f"Comparecimento    : {milhar(COMPARECIMENTO_TOTAL):>15}")
print(f"Abstenções        : {milhar(ABSTENCAO_TOTAL):>15}")
print(f"Taxa de abstenção : {pct(TAXA_NACIONAL):>15}")
print("-" * 46)
print("Seções:", milhar(len(abstencao_secao)), "| Locais:", milhar(len(abstencao_local)),
      "| Locais no mapa:", milhar(len(mapa_final)))
display(formatar_resumo(resumo_nacional))

ELEIÇÃO 2026 — 1.º TURNO — PRESIDENTE
----------------------------------------------
Eleitores aptos   :     158.745.502
Comparecimento    :     125.275.835
Abstenções        :      33.469.667
Taxa de abstenção :          21,08%
----------------------------------------------
Seções: 517.179 | Locais: 94.299 | Locais no mapa: 93.535


,Calculado,Oficial TSE,Diferença
Aptos,158.745.502,158.745.502,0
Comparecimento,125.275.835,125.275.835,0
Abstenção,33.469.667,33.469.244,423
Taxa (%),"21,08","21,08","0,00"
